In [0]:
spark.sql("CREATE DATABASE IF NOT EXISTS cinedata.gold")

DataFrame[]

In [0]:
import pyspark.sql.functions as F

# dim_genres, dim_people e dim_companies

In [0]:
# 1. gold.dim_genres
df_silver_generos = spark.table("cinedata.silver.tb_generos")

df_dim_genres = (
    df_silver_generos
    .select("nome_genero")
    .dropDuplicates()
    .withColumn("sk_genre_id", F.monotonically_increasing_id())
    .select("sk_genre_id", "nome_genero")
)

(
    df_dim_genres.write.format("delta")
    .mode("overwrite")
    .saveAsTable("cinedata.gold.dim_genres")
)

In [0]:
# 2. gold.dim_people
df_silver_pessoas = spark.table("cinedata.silver.tb_pessoas_empresas")

df_dim_people = (
    df_silver_pessoas
    .filter(F.col("papel_atuacao").isin("Ator", "Diretor", "Roteirista"))
    .select(
        F.col("nome_pessoa_empresa").alias("nome_pessoa"), 
        F.col("papel_atuacao").alias("tipo_pessoa") # Renomeia a coluna corretamente
    )
    .dropDuplicates()
    .withColumn("sk_person_id", F.monotonically_increasing_id())
    .select("sk_person_id", "nome_pessoa", "tipo_pessoa")
)

(
    df_dim_people.write.format("delta")
    .mode("overwrite")
    .saveAsTable("cinedata.gold.dim_people")
)

In [0]:
# 3. gold.dim_companies
df_dim_companies = (
    df_silver_pessoas
    .filter(F.col("papel_atuacao") == "Produtora")
    .select(F.col("nome_pessoa_empresa").alias("nome_produtora"))
    .dropDuplicates()
    .withColumn("sk_company_id", F.monotonically_increasing_id())
    .select("sk_company_id", "nome_produtora")
)

(
    df_dim_companies.write.format("delta")
    .mode("overwrite")
    .saveAsTable("cinedata.gold.dim_companies")
)

display(df_dim_genres)
display(df_dim_people)
display(df_dim_companies)

sk_genre_id,nome_genero
0,Horror
1,Comedy
2,Family
3,Music
4,Thriller
5,Action
6,Crime
7,Drama
8,Animation
9,Fantasy


sk_person_id,nome_pessoa,tipo_pessoa
0,Ryan Moore,Ator
1,Rainn Wilson,Ator
2,Tui Asau,Ator
3,Kostiantyn Stepankov,Ator
4,Alicia Vikander,Ator
5,Katie Alexander Thom,Ator
6,Eriq La Salle,Ator
7,Harry Shum Jr.,Ator
8,Erando González,Ator
9,Jeff Dorchen,Ator


sk_company_id,nome_produtora
0,Waddieish Claretrap
1,LStar Capital
2,Sliding Down Rainbows Entertainment
3,Village Studios
4,Fuji Television Network
5,Paradox Studios
6,Sony Pictures Animation
7,Safier Entertainment
8,DMG Entertainment
9,Anton Capital Entertainment


# dim_movies e dim_reviews

In [0]:
import pyspark.sql.functions as F

In [0]:
# ==========================================
# 1. gold.dim_movies
# ==========================================
df_silver_info = spark.table("cinedata.silver.tb_info_filmes")

df_dim_movies = (
    df_silver_info
    .dropDuplicates(["id_filme"]) # Garantia extra de unicidade do grão
    .withColumn("sk_movie_id", F.monotonically_increasing_id())
    .select(
        "sk_movie_id",
        "id_filme",
        "titulo",
        "data_lancamento",
        "ano_lancamento",
        "duracao_minutos",
        "idioma_original",
        "status_filme",
        "sinopse"
    )
)

(
    df_dim_movies.write.format("delta")
    .mode("overwrite")
    .saveAsTable("cinedata.gold.dim_movies")
)
print("gold.dim_movies criada com sucesso!")

gold.dim_movies criada com sucesso!


In [0]:

# ==========================================
# 2. gold.dim_reviews
# ==========================================
df_silver_reviews = spark.table("cinedata.silver.tb_avaliacoes_usuarios")

# 2.1 Agregar as métricas por filme
df_reviews_agg = (
    df_silver_reviews
    .groupBy("id_filme")
    .agg(
        F.count("*").alias("qtd_avaliacoes_usuarios"),
        F.round(F.avg("nota_usuario"), 2).alias("nota_media_usuarios")
    )
)

# 2.2 Fazer o Join com a dim_movies para obter a sk_movie_id e gerar a PK da review
df_dim_reviews = (
    df_reviews_agg
    .join(df_dim_movies, df_reviews_agg.id_filme == df_dim_movies.id_filme, "inner")
    .withColumn("sk_review_id", F.monotonically_increasing_id())
    .select(
        "sk_review_id",
        "sk_movie_id",
        "qtd_avaliacoes_usuarios",
        "nota_media_usuarios"
    )
)

(
    df_dim_reviews.write.format("delta")
    .mode("overwrite")
    .saveAsTable("cinedata.gold.dim_reviews")
)
print("gold.dim_reviews criada com sucesso!")

display(df_dim_movies)
display(df_dim_reviews)

gold.dim_reviews criada com sucesso!


sk_movie_id,id_filme,titulo,data_lancamento,ano_lancamento,duracao_minutos,idioma_original,status_filme,sinopse
0,14564,Rings,2017-02-01,2017,102,en,Lançado,"\Julia becomes worried about her boyfriend Holt when he explores the dark urban legend of a mysterious videotape said to kill the watcher seven days after viewing. She sacrifices herself to save her boyfriend and in doing so makes a horrifying discovery: there is a \""\""movie within the movie\""\"" that no one has ever seen before.\"""""
1,32471,Mixtape,2021-12-03,2021,94,en,Lançado,null
2,38258,Grizzly II: Revenge,2020-02-17,2020,74,en,Lançado,\All hell breaks loose when a giant grizzly
3,38492,Billy Joel - Live at Yankee Stadium,2022-06-22,2022,86,en,Lançado,Billy Joel plays his greatest hits in the Big Apple.
4,38700,Bad Boys for Life,2020-01-15,2020,124,en,Lançado,"Marcus and Mike are forced to confront new threats, career changes, and midlife crises as they join the newly created elite team AMMO of the Miami police department to take down the ruthless Armando Armas, the vicious leader of a Miami drug cartel."
5,42018,The Horse Thief,2019-03-19,2019,88,zh,Lançado,"Devout Buddhists, Norbu and Dolma live with their young son Tashi in a clan in Tibet. Norbu is a highwayman. After Norbu is charged with stealing from the temple, he and his family are banished. Impoverished and marginalized, they can do little when their beloved son becomes ill. Tashi dies of a fever. After a second son is born, Norbu focuses his every action on keeping this child alive, seeking re-admission to the clan for his wife and child, then risking all to save them from isolation and starvation in winter."
6,42330,Monkey Magic,2018-09-22,2018,66,zh,Lançado,"Dearth Voyd, the ruler of the dark side of the universe, wants to turn the human world into a place of violence and evil!! However, a huge meteor falls upon Flower-Fruit mountain giving birth to Kongo, a monkey made of stone! Kongo, now sets out on his quest to fight evil and restore order to a desperate land. Episodes 1-3"
7,43074,Ghostbusters,2016-07-14,2016,117,en,Lançado,"Following a ghost invasion of Manhattan, paranormal enthusiasts Erin Gilbert and Abby Yates, nuclear engineer Jillian Holtzmann, and subway worker Patty Tolan band together to stop the otherworldly threat."
8,45033,20 Seconds of Joy,2018-01-01,2018,60,de,Lançado,"Traces the story of an extreme athlete, past and present; but also explores the psychology behind life, death, risk and the confrontation of fear."
9,46983,The Song of Styrene,2022-05-23,2022,13,fr,Lançado,Le chant du Styrène is a 1958 French documentary film directed by Alain Resnais. The film was an order by French industrial group Pechiney to highlight the merits of plastics.


sk_review_id,sk_movie_id,qtd_avaliacoes_usuarios,nota_media_usuarios
0,2,2,2.2
1,3,1,null
2,4,1,3.6
3,6,1,8.6
4,14,1,6.0
5,16,1,null
6,22,1,0.8
7,23,1,2.6
8,25,1,2.1
9,27,1,5.7


# bridge_movie_genre, bridge_movie_person, bridge_movie_company

In [0]:
import pyspark.sql.functions as F

In [0]:
# 1. Carregar as tabelas necessárias
df_silver_generos = spark.table("cinedata.silver.tb_generos")
df_silver_pessoas = spark.table("cinedata.silver.tb_pessoas_empresas")

df_dim_movies = spark.table("cinedata.gold.dim_movies")
df_dim_genres = spark.table("cinedata.gold.dim_genres")
df_dim_people = spark.table("cinedata.gold.dim_people")
df_dim_companies = spark.table("cinedata.gold.dim_companies")

In [0]:
# ==========================================
# 2. gold.bridge_movie_genre
# ==========================================
df_bridge_genre = (
    df_silver_generos
    .join(df_dim_genres, "nome_genero", "inner")
    .join(df_dim_movies, "id_filme", "inner")
    .select("sk_movie_id", "sk_genre_id")
    .dropDuplicates()
)

(
    df_bridge_genre.write.format("delta")
    .mode("overwrite")
    .saveAsTable("cinedata.gold.bridge_movie_genre")
)

In [0]:
# ==========================================
# 3. gold.bridge_movie_person
# ==========================================
df_bridge_person = (
    df_silver_pessoas
    .filter(F.col("papel_atuacao").isin("Ator", "Diretor", "Roteirista"))
    .join(
        df_dim_people, 
        (df_silver_pessoas.nome_pessoa_empresa == df_dim_people.nome_pessoa) & 
        (df_silver_pessoas.papel_atuacao == df_dim_people.tipo_pessoa), 
        "inner"
    )
    .join(df_dim_movies, "id_filme", "inner")
    .select("sk_movie_id", "sk_person_id")
    .dropDuplicates()
)

(
    df_bridge_person.write.format("delta")
    .mode("overwrite")
    .saveAsTable("cinedata.gold.bridge_movie_person")
)


In [0]:

# ==========================================
# 4. gold.bridge_movie_company
# ==========================================
df_bridge_company = (
    df_silver_pessoas
    .filter(F.col("papel_atuacao") == "Produtora")
    .join(
        df_dim_companies, 
        df_silver_pessoas.nome_pessoa_empresa == df_dim_companies.nome_produtora, 
        "inner"
    )
    .join(df_dim_movies, "id_filme", "inner")
    .select("sk_movie_id", "sk_company_id")
    .dropDuplicates()
)

(
    df_bridge_company.write.format("delta")
    .mode("overwrite")
    .saveAsTable("cinedata.gold.bridge_movie_company")
)

display(df_bridge_genre)
display(df_bridge_person)
display(df_bridge_company)

sk_movie_id,sk_genre_id
60103,10
16367,4
1,16
5497,16
70781,15
2,16
10874,6
54598,0
5501,12
81669,11


sk_movie_id,sk_person_id
21962,131327
38259,4
38265,26377
27438,314818
43885,288625
65663,209521
38430,131336
92778,52498
16672,262171
76625,131341


sk_movie_id,sk_company_id
38454,8724
38666,17478
60595,5822
11334,43630
6092,40744
87704,17482
93246,35048
38990,43641
6275,8740
44537,2949


# Tabela fato

In [0]:
import pyspark.sql.functions as F


In [0]:
# 1. Carregar as tabelas de origem e a dimensão central
df_dim_movies = spark.table("cinedata.gold.dim_movies")
df_silver_fin = spark.table("cinedata.silver.tb_financeiro_filmes")
df_silver_metrics = spark.table("cinedata.silver.tb_metricas_engajamento")

# 2. Construir a Fato cruzando por id_filme
df_fact_movies = (
    df_dim_movies
    .select("sk_movie_id", "id_filme")
    .join(df_silver_fin, df_dim_movies.id_filme == df_silver_fin.id_filme, "left")
    .join(df_silver_metrics, df_dim_movies.id_filme == df_silver_metrics.id_filme, "left")
    .select(
        "sk_movie_id",
        # Métricas Financeiras (DECIMAL)
        F.col("orcamento_usd"),
        F.col("receita_usd"),
        F.col("lucro_usd"),
        F.col("orcamento_brl"),
        F.col("receita_brl"),
        F.col("lucro_brl"),
        # Métricas de Engajamento (DOUBLE / INT)
        F.col("popularidade"),
        F.col("nota_media_tmdb"),
        F.col("qtd_votos_tmdb"),
        F.col("nota_media_imdb"),
        F.col("qtd_votos_imdb")
    )
)

# 3. Gravar a tabela final na camada Gold
(
    df_fact_movies.write.format("delta")
    .mode("overwrite")
    .saveAsTable("cinedata.gold.fact_movies_performance")
)

print("gold.fact_movies_performance criada e gravada com sucesso!")
display(df_fact_movies)

gold.fact_movies_performance criada e gravada com sucesso!


sk_movie_id,orcamento_usd,receita_usd,lucro_usd,orcamento_brl,receita_brl,lucro_brl,popularidade,nota_media_tmdb,qtd_votos_tmdb,nota_media_imdb,qtd_votos_imdb
0,null,null,null,null,null,null,1.561,10.0,1,6.4,34
1,46000000.00,23737523.00,-22262477.00,228583200.00,117956499.29,-110626700.71,28.9,7.119,2822,7.2,135908
2,null,2550321.00,null,null,12673055.11,null,13.257,6.348,282,6.4,20064
3,73000000.00,349779543.00,276779543.00,362751600.00,1738124505.08,1375372905.08,24.75,6.205,3369,null,120814
4,21000000.00,113118226.00,92118226.00,104353200.00,562107088.64,457753888.64,24.949,5.723,2966,5.7,106542
5,null,null,null,null,null,null,0.6,6.0,5,7.0,80
6,null,null,null,null,null,null,0.638,0.0,0,6.3,64
7,2000000.00,37858128.00,35858128.00,9938400.00,188124609.66,178186209.66,4.385,7.655,475,6.7,4079
8,5000000.00,6341855.00,1341855.00,24846000.00,31513945.87,6667945.87,12.143,5.354,513,5.3,15068
9,null,null,null,null,null,null,1.601,7.4,null,7.5,null
